In [1]:
%matplotlib notebook
%load_ext autoreload
%autoreload 2

In [2]:
import os, sys

module_path = os.path.abspath(os.path.join("../.."))
sys.path.append(module_path)

## Dataset and hyperparameters loading

In [21]:
from torchvision.transforms.v2 import Compose
import torch

from SLTDataset import SLTDataset
from hyperparameters import load_hyperparameters_from_json


DATASET = "GSL"
EXPERIMENT_ID = "firm-frog-32"
SAMPLE_IDX = 509

# device set to cpu to avoid memory issues
device = torch.device("cpu")

dataset_path = f"/mnt/disk3Tb/slt-datasets/{DATASET}"
experiment_path = f"results/{DATASET}/{EXPERIMENT_ID}"
hp = load_hyperparameters_from_json(f"{experiment_path}/hp.json")
interp_path = f"{experiment_path}/interp"
output_path = f"{interp_path}/{SAMPLE_IDX}/"
os.makedirs(output_path, exist_ok=True)
transparent_plot = False
decoder_attn_weights_layer = 0

transforms: Compose = Compose(hp["TRANSFORMS"])

train_dataset = SLTDataset(
    data_dir=dataset_path,
    split="train",
    input_mode=hp["INPUT_MODE"],
    output_mode=hp["OUTPUT_MODE"],
    transforms=transforms,
    max_tokens=hp["MAX_TOKENS"],
)
test_dataset = SLTDataset(
    data_dir=dataset_path,
    split="test",
    input_mode=hp["INPUT_MODE"],
    output_mode=hp["OUTPUT_MODE"],
    transforms=transforms,
    max_tokens=hp["MAX_TOKENS"],
)

Loaded metadata for dataset: The Greek Sign Language (GSL) Dataset
Loaded train annotations at /mnt/disk3Tb/slt-datasets/GSL/annotations.csv


Validating files: 100%|██████████| 8821/8821 [00:00<00:00, 198631.81it/s]


Dataset loaded correctly

Loaded metadata for dataset: The Greek Sign Language (GSL) Dataset
Loaded test annotations at /mnt/disk3Tb/slt-datasets/GSL/annotations.csv


Validating files: 100%|██████████| 881/881 [00:00<00:00, 209121.78it/s]

Dataset loaded correctly



### Display sample

In [13]:
from IPython.display import HTML

# avoid using the last transform as it flattens the keypoints
visual_transforms: Compose = Compose(hp["TRANSFORMS"][:-1])
anim = test_dataset.visualize_pose(SAMPLE_IDX, transforms=visual_transforms)
HTML(anim.to_jshtml())

<IPython.core.display.Javascript object>

In [14]:
anim.save(f"{output_path}/sample.mp4", writer="ffmpeg")

In [15]:
src, tgt = test_dataset[SAMPLE_IDX]
src = src.unsqueeze(0)
tgt = tgt.unsqueeze(0)
src = src.to(device)
tgt = tgt.to(device)

## Model

### Definition

In [16]:
import glob
from LightningKeypointsTransformer import LKeypointsTransformer

checkpoint_path = glob.glob(f"{experiment_path}/best*")[0]
l_model = LKeypointsTransformer.load_from_checkpoint(
    checkpoint_path, map_location=device, hp=hp, interp=True, device=device
)
l_model.model = l_model.model.to(device)
model = l_model.model.eval()
translator = l_model.translator

/home/ostanchi/miniconda3/envs/captum/lib/python3.10/site-packages/torch/nn/modules/transformer.py:307: UserWarning: enable_nested_tensor is True, but self.use_nested_tensor is False because encoder_layer.self_attn.batch_first was not True(use batch_first for better inference performance)
  warnings.warn(f"enable_nested_tensor is True, but self.use_nested_tensor is False because {why_not_sparsity_fast_path}")


In [17]:
model.training, next(model.parameters()).device

(False, device(type='cpu'))

In [22]:
BOS_IDX = train_dataset.tokenizer.cls_token_id
EOS_IDX = train_dataset.tokenizer.sep_token_id

### Interpretability

In [19]:
from interp.plot_functions import *

In [23]:
translation = translator.translate(src, model, "greedy", train_dataset.tokenizer)
translation = ["BOS " + s + " EOS" for s in translation]
translation = translation[0].split()
translation

['BOS', 'ΜΩΡΟ', 'ΓΕΝΝΩ', 'ΝΩΡΙΣ', 'EOS']

In [24]:
# FIXME
translation = ["BOS"] + translation

In [25]:
import pickle

with open(f"{interp_path}/encoder_sa.pkl", "rb") as f:
    encoder_sa = pickle.load(f)
with open(f"{interp_path}/decoder_sa.pkl", "rb") as f:
    decoder_sa = pickle.load(f)
with open(f"{interp_path}/decoder_ca.pkl", "rb") as f:
    decoder_ca = pickle.load(f)

/home/ostanchi/miniconda3/envs/captum/lib/python3.10/site-packages/torch/storage.py:414: FutureWarning: You are using `torch.load` with `weights_only=False` (the current default value), which uses the default pickle module implicitly. It is possible to construct malicious pickle data which will execute arbitrary code during unpickling (See https://github.com/pytorch/pytorch/blob/main/SECURITY.md#untrusted-models for more details). In a future release, the default value for `weights_only` will be flipped to `True`. This limits the functions that could be executed during unpickling. Arbitrary objects will no longer be allowed to be loaded via this mode unless they are explicitly allowlisted by the user via `torch.serialization.add_safe_globals`. We recommend you start setting `weights_only=True` for any use case where you don't have full control of the loaded file. Please open an issue on GitHub for any issues related to this experimental feature.
  return torch.load(io.BytesIO(b))


In [26]:
def flatten(tensor_dict: Dict[int, List[torch.Tensor]]) -> List[torch.Tensor]:
    return [t.squeeze(0) for tensors in tensor_dict.values() for t in tensors]

#### Encoder Self-Attention

In [27]:
attn_output_weights_list = flatten(encoder_sa[SAMPLE_IDX])

In [28]:
# FIXME
attn_output_weights_list = reorganize_list(
    attn_output_weights_list, len(translation) - 1
)

In [29]:
plot_encoder_layers(attn_output_weights_list, hp, output_path, transparent_plot)

<IPython.core.display.Javascript object>

#### Decoder Self-Attention

In [30]:
attn_output_weights_list = flatten(decoder_sa[SAMPLE_IDX])

In [31]:
# FIXME
attn_output_weights_list = reorganize_list(
    attn_output_weights_list, len(translation) - 1
)

In [32]:
plot_decoder_layers(
    attn_output_weights_list, hp, output_path, translation, "self", transparent_plot
)

<IPython.core.display.Javascript object>

#### Decoder Cross-Attention

In [33]:
attn_output_weights_list = flatten(decoder_ca[SAMPLE_IDX])

In [34]:
# FIXME
attn_output_weights_list = reorganize_list(
    attn_output_weights_list, len(translation) - 1
)

In [35]:
plot_decoder_layers(
    attn_output_weights_list, hp, output_path, translation, "cross", transparent_plot
)

<IPython.core.display.Javascript object>

In [36]:
norm_min_max_lambda = lambda t: (t - t.min()) / (t.max() - t.min())

In [37]:
for mode in ["heatmap", "lineplot"]:
    attn_weights = plot_decoder_attn_weights(
        attn_output_weights_list,
        hp,
        output_path,
        translation,
        decoder_attn_weights_layer,
        norm_min_max_lambda,
        mode,
        transparent_plot,
        {"square": True, "cbar": False},
    )

<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>

In [38]:
anim = plot_decoder_attn_weights_bars(
    src.cpu(), attn_weights, hp, output_path, translation, decoder_attn_weights_layer
)

<IPython.core.display.Javascript object>

In [39]:
HTML(anim.to_jshtml())

#### Decoder `sa_block` & `mha_block`

In [43]:
with open(f"{interp_path}/intermediate_outputs.pkl", "rb") as f:
    intermediate_outputs = pickle.load(f)

In [44]:
intermediate_outputs = intermediate_outputs[SAMPLE_IDX]

In [45]:
plot_intermediate_outputs(
    intermediate_outputs, hp, output_path, translation, transparent_plot
)

<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>

In [46]:
diff_sa_mha_block = []
for t1, t2 in zip(intermediate_outputs["sa_block"], intermediate_outputs["mha_block"]):
    diff = t1 - t2

    # normalize to [-1,1]
    diff -= diff.min()
    diff /= diff.max()
    diff *= 2
    diff -= 1

    diff_sa_mha_block.append(diff)
diff_sa_mha_block = {"diff_sa_block_mha_block": diff_sa_mha_block}

In [47]:
plot_intermediate_outputs(
    diff_sa_mha_block, hp, output_path, translation, transparent_plot
)

<IPython.core.display.Javascript object>

In [48]:
tgt_length = len(translation) - 1  # from BOS to EOS-1
attn_output_weights_list = reorganize_list(
    diff_sa_mha_block["diff_sa_block_mha_block"], hp["NUM_DECODER_LAYERS"]
)
for i in range(0, len(attn_output_weights_list), tgt_length):
    print(f"Layer {i // tgt_length + 1}:")
    for j in range(i, i + tgt_length):
        w = attn_output_weights_list[j]
        print(f"{w.shape} → {w.mean():>7.3f}")

Layer 1:
(1, 128) →   0.193
(2, 128) →   0.120
(3, 128) →   0.002
(4, 128) →  -0.016
(5, 128) →  -0.028
Layer 2:
(1, 128) →   0.093
(2, 128) →   0.032
(3, 128) →  -0.015
(4, 128) →   0.028
(5, 128) →   0.030
Layer 3:
(1, 128) →   0.009
(2, 128) →   0.304
(3, 128) →   0.275
(4, 128) →   0.225
(5, 128) →   0.151
Layer 4:
(1, 128) →  -0.165
(2, 128) →   0.004
(3, 128) →  -0.023
(4, 128) →  -0.071
(5, 128) →   0.035
